In [1]:
%pip install -q ydata-profiling  # pandas-profiling was renamed to ydata-profiling


[notice] A new release of pip is available: 24.0 -> 26.2.1
[notice] To update, run: python3 -m pip install --upgrade pip


Note: you may need to restart the kernel to use updated packages.


# Importing the data


In [2]:
import pandas as pd
data = pd.read_csv('data/weatherAUS.csv')

# Analysing the data

In [3]:
data.info()

<class 'pandas.core.frame.DataFrame'>
RangeIndex: 145460 entries, 0 to 145459
Data columns (total 23 columns):
 #   Column         Non-Null Count   Dtype  
---  ------         --------------   -----  
 0   Date           145460 non-null  object 
 1   Location       145460 non-null  object 
 2   MinTemp        143975 non-null  float64
 3   MaxTemp        144199 non-null  float64
 4   Rainfall       142199 non-null  float64
 5   Evaporation    82670 non-null   float64
 6   Sunshine       75625 non-null   float64
 7   WindGustDir    135134 non-null  object 
 8   WindGustSpeed  135197 non-null  float64
 9   WindDir9am     134894 non-null  object 
 10  WindDir3pm     141232 non-null  object 
 11  WindSpeed9am   143693 non-null  float64
 12  WindSpeed3pm   142398 non-null  float64
 13  Humidity9am    142806 non-null  float64
 14  Humidity3pm    140953 non-null  float64
 15  Pressure9am    130395 non-null  float64
 16  Pressure3pm    130432 non-null  float64
 17  Cloud9am       89572 non-null

In [4]:
from ydata_profiling import ProfileReport
ProfileReport(data, title="Rain in Australia Data Analysis", explorative=True)

/tmp/ipykernel_13749/1195783038.py:1: DeprecationWarning: 
    `import ydata_profiling` is deprecated and will not receive more updates. 
    Please install fg-data-profiling via `pip install fg-data-profiling` and use `import data_profiling` instead.
    
  from ydata_profiling import ProfileReport


Summarize dataset:   0%|          | 0/5 [00:00<?, ?it/s]

  0%|          | 0/23 [00:00<?, ?it/s]

  4%|▍         | 1/23 [00:01<00:30,  1.38s/it]

  9%|▊         | 2/23 [00:01<00:13,  1.58it/s]

...

 96%|█████████▌| 22/23 [00:05<00:00,  5.30it/s]

100%|██████████| 23/23 [00:06<00:00,  3.95it/s]

100%|██████████| 23/23 [00:06<00:00,  3.82it/s]

Generate report structure:   0%|          | 0/1 [00:00<?, ?it/s]

Render HTML:   0%|          | 0/1 [00:00<?, ?it/s]

# Preprocessing the Data

In [5]:
columns = {i: col for i, col in enumerate(data.columns)}
num = [2, 3, 4, 5, 6, 8, 11, 12, 13, 14, 15, 16, 19, 20]
cat = [1, 7, 9, 10, 17, 18]
print(columns)

{0: 'Date', 1: 'Location', 2: 'MinTemp', 3: 'MaxTemp', 4: 'Rainfall', 5: 'Evaporation', 6: 'Sunshine', 7: 'WindGustDir', 8: 'WindGustSpeed', 9: 'WindDir9am', 10: 'WindDir3pm', 11: 'WindSpeed9am', 12: 'WindSpeed3pm', 13: 'Humidity9am', 14: 'Humidity3pm', 15: 'Pressure9am', 16: 'Pressure3pm', 17: 'Cloud9am', 18: 'Cloud3pm', 19: 'Temp9am', 20: 'Temp3pm', 21: 'RainToday', 22: 'RainTomorrow'}


## Remove all the rows where the RainTomorrow value is missing 

In [6]:
for col in [21, 22]:
  data = data[data[columns[col]].notna()]

## Remove the duplicates

In [7]:
data.drop_duplicates(inplace=True)

## Map the 'Yes' and 'No' values in the RainToday and RainTomorrow columns

In [8]:
for c in [21, 22]:
  data[columns[c]] = data[columns[c]].replace({'Yes': 1, 'No': 0, 'YesS': 1})

## Fill the missing values in the RainToday column based on the Rainfall columns

In [9]:
# RainToday is 1 when more than 1 mm of rain fell that day, so a missing RainToday can be
# filled from Rainfall when that is known.
missing = data[columns[21]].isna() & data[columns[4]].notna()
data.loc[missing, columns[21]] = (data.loc[missing, columns[4]] > 1.0).astype(int)

## Replace the missing values

In [10]:
for col in num: # numerical attributes
  new_val = round(data[columns[col]].mean(), 1)
  data[columns[col]] = data[columns[col]].fillna(new_val)

for col in cat: # categorical attributes
  new_val = data[columns[col]].value_counts().idxmax()  # most frequent category
  data[columns[col]] = data[columns[col]].fillna(new_val)

## Encoding the categorical columns

In [11]:
from sklearn import preprocessing as pre
le = pre.LabelEncoder()
for col in [columns[c] for c in cat]:
  data[col] = le.fit_transform(data[col].astype(str))

## Drop the highly correlated columns

In [12]:
data.drop([columns[c] for c in [0, 13, 19, 20]], axis=1, inplace=True)

## Check for any missing values

In [13]:
print(data.isna().sum())
print("Number of columns: " + str(len(data.columns)))

Location         0
MinTemp          0
MaxTemp          0
Rainfall         0
Evaporation      0
Sunshine         0
WindGustDir      0
WindGustSpeed    0
WindDir9am       0
WindDir3pm       0
WindSpeed9am     0
WindSpeed3pm     0
Humidity3pm      0
Pressure9am      0
Pressure3pm      0
Cloud9am         0
Cloud3pm         0
RainToday        0
RainTomorrow     0
dtype: int64
Number of columns: 19


## Separate the data into train and test data
21000 rows - train

9000 rows - test

In [14]:
from sklearn.model_selection import train_test_split
df = data.groupby('RainTomorrow').sample(n=15000, replace=False, random_state=42)  # balanced classes
print(df.shape[0])
print(df['RainTomorrow'].unique())
x = df[df.columns[0:18]]
y = df[df.columns[18]].astype(int)
x_train, x_test, y_train, y_test = train_test_split(x, y, test_size=0.3, random_state=42)

# Standardise with the training set's statistics (logistic regression, KNN and the SVM
# are sensitive to feature scale; the tree models and naive Bayes are not affected much).
scaler = pre.StandardScaler().fit(x_train)
x_train, x_test = scaler.transform(x_train), scaler.transform(x_test)

30000
[0 1]


# Models

In [15]:
from sklearn.model_selection import RepeatedStratifiedKFold
from sklearn.model_selection import GridSearchCV
import matplotlib.pyplot as plt
import numpy as np
import seaborn as sns
from sklearn.metrics import confusion_matrix, accuracy_score
cv = RepeatedStratifiedKFold(n_splits=10, n_repeats=3, random_state=42)

## Naive Bayes

In [16]:
from sklearn.naive_bayes import GaussianNB
gnb_params = {
    'var_smoothing': [1e-1, 1e-2, 1e-3, 1e-4, 1e-5, 1e-6, 1e-7, 1e-8, 1e-9]
}
gnb = GaussianNB()
search = GridSearchCV(gnb, gnb_params, scoring='accuracy', n_jobs=-1, cv=cv)
result = search.fit(x_train, y_train)
print('Best Score: %s' % result.best_score_)
print('Best Hyperparameters: %s' % result.best_params_)


Best Score: 0.7481746031746032
Best Hyperparameters: {'var_smoothing': 0.1}


In [17]:
scores = np.array(result.cv_results_['mean_test_score'])

plt.plot(gnb_params['var_smoothing'], scores)
plt.xlabel('var_smoothing')
plt.ylabel('Mean score')
plt.show()

In [18]:
y_pred = result.predict(x_test)
cf_matrix = confusion_matrix(y_test, y_pred)
sns.heatmap(cf_matrix, annot=True)
print("The accuracy score is: " + str(accuracy_score(y_test, y_pred)))

The accuracy score is: 0.75


## Logistic Regression

In [19]:
from sklearn.linear_model import LogisticRegression
lr_params = {
    'solver': ['sag', 'saga'],
    'max_iter': [500, 1000, 1500, 2000]
}
lr = LogisticRegression(random_state=42)
search = GridSearchCV(lr, lr_params, scoring='accuracy', n_jobs=-1, cv=cv)
result = search.fit(x_train, y_train)
print('Best Score: %s' % result.best_score_)
print('Best Hyperparameters: %s' % result.best_params_)

Best Score: 0.7813650793650793
Best Hyperparameters: {'max_iter': 500, 'solver': 'sag'}


In [20]:
scores = np.array(result.cv_results_['mean_test_score']).reshape(len(lr_params['solver']), len(lr_params['max_iter']))

for ind, i in enumerate(lr_params['solver']):
    plt.plot(lr_params['max_iter'], scores[ind], label='solver: ' + str(i))

plt.legend()
plt.xlabel('max_iter')
plt.ylabel('Mean score')
plt.show()

In [21]:
y_pred = result.predict(x_test)
cf_matrix = confusion_matrix(y_test, y_pred)
sns.heatmap(cf_matrix, annot=True)
print("The accuracy score is: " + str(accuracy_score(y_test, y_pred)))

The accuracy score is: 0.7847777777777778


## K-Nearest Neighbors

In [22]:
from sklearn.neighbors import KNeighborsClassifier
knn_params = {
    'n_neighbors': [5, 10, 15, 20],
    'p': [1, 2]
}
knn = KNeighborsClassifier()
search = GridSearchCV(knn, knn_params, scoring='accuracy', n_jobs=-1, cv=cv)
result = search.fit(x_train, y_train)
print('Best Score: %s' % result.best_score_)
print('Best Hyperparameters: %s' % result.best_params_)


Best Score: 0.7805079365079365
Best Hyperparameters: {'n_neighbors': 15, 'p': 1}


In [23]:
scores = np.array(result.cv_results_['mean_test_score']).reshape(len(knn_params['p']), len(knn_params['n_neighbors']))

for ind, i in enumerate(knn_params['p']):
    plt.plot(knn_params['n_neighbors'], scores[ind], label='p: ' + str(i))

plt.legend()
plt.xlabel('n_neighbors')
plt.ylabel('Mean score')
plt.show()

In [24]:
y_pred = result.predict(x_test)
cf_matrix = confusion_matrix(y_test, y_pred)
sns.heatmap(cf_matrix, annot=True)
print("The accuracy score is: " + str(accuracy_score(y_test, y_pred)))

The accuracy score is: 0.7827777777777778


## Linear Support Vector Classification

In [25]:
from sklearn.svm import LinearSVC
lsvc_params = {
    'loss': ['hinge', 'squared_hinge'],
    'max_iter': [500, 1000, 1500, 2000]
}
lsvc = LinearSVC(random_state=42)
search = GridSearchCV(lsvc, lsvc_params, scoring='accuracy', n_jobs=-1, cv=cv)
result = search.fit(x_train, y_train)
print('Best Score: %s' % result.best_score_)
print('Best Hyperparameters: %s' % result.best_params_)


/tmp/claude-0/-home-user/cd3bd136-ab75-5641-9c58-438f3eb543f9/scratchpad/venv/lib/python3.11/site-packages/sklearn/svm/_base.py:1295: ConvergenceWarning: Liblinear failed to converge, increase the number of iterations.
  warnings.warn(
/tmp/claude-0/-home-user/cd3bd136-ab75-5641-9c58-438f3eb543f9/scratchpad/venv/lib/python3.11/site-packages/sklearn/svm/_base.py:1295: ConvergenceWarning: Liblinear failed to converge, increase the number of iterations.
  warnings.warn(
/tmp/claude-0/-home-user/cd3bd136-ab75-5641-9c58-438f3eb543f9/scratchpad/venv/lib/python3.11/site-packages/sklearn/svm/_base.py:1295: ConvergenceWarning: Liblinear failed to converge, increase the number of iterations.
  warnings.warn(
/tmp/claude-0/-home-user/cd3bd136-ab75-5641-9c58-438f3eb543f9/scratchpad/venv/lib/python3.11/site-packages/sklearn/svm/_base.py:1295: ConvergenceWarning: Liblinear failed to converge, increase the number of iterations.
  warnings.warn(


/tmp/claude-0/-home-user/cd3bd136-ab75-5641-9c58-438f3eb543f9/scratchpad/venv/lib/python3.11/site-packages/sklearn/svm/_base.py:1295: ConvergenceWarning: Liblinear failed to converge, increase the number of iterations.
  warnings.warn(
/tmp/claude-0/-home-user/cd3bd136-ab75-5641-9c58-438f3eb543f9/scratchpad/venv/lib/python3.11/site-packages/sklearn/svm/_base.py:1295: ConvergenceWarning: Liblinear failed to converge, increase the number of iterations.
  warnings.warn(
/tmp/claude-0/-home-user/cd3bd136-ab75-5641-9c58-438f3eb543f9/scratchpad/venv/lib/python3.11/site-packages/sklearn/svm/_base.py:1295: ConvergenceWarning: Liblinear failed to converge, increase the number of iterations.
  warnings.warn(


/tmp/claude-0/-home-user/cd3bd136-ab75-5641-9c58-438f3eb543f9/scratchpad/venv/lib/python3.11/site-packages/sklearn/svm/_base.py:1295: ConvergenceWarning: Liblinear failed to converge, increase the number of iterations.
  warnings.warn(
/tmp/claude-0/-home-user/cd3bd136-ab75-5641-9c58-438f3eb543f9/scratchpad/venv/lib/python3.11/site-packages/sklearn/svm/_base.py:1295: ConvergenceWarning: Liblinear failed to converge, increase the number of iterations.
  warnings.warn(
/tmp/claude-0/-home-user/cd3bd136-ab75-5641-9c58-438f3eb543f9/scratchpad/venv/lib/python3.11/site-packages/sklearn/svm/_base.py:1295: ConvergenceWarning: Liblinear failed to converge, increase the number of iterations.
  warnings.warn(


/tmp/claude-0/-home-user/cd3bd136-ab75-5641-9c58-438f3eb543f9/scratchpad/venv/lib/python3.11/site-packages/sklearn/svm/_base.py:1295: ConvergenceWarning: Liblinear failed to converge, increase the number of iterations.
  warnings.warn(
/tmp/claude-0/-home-user/cd3bd136-ab75-5641-9c58-438f3eb543f9/scratchpad/venv/lib/python3.11/site-packages/sklearn/svm/_base.py:1295: ConvergenceWarning: Liblinear failed to converge, increase the number of iterations.
  warnings.warn(


/tmp/claude-0/-home-user/cd3bd136-ab75-5641-9c58-438f3eb543f9/scratchpad/venv/lib/python3.11/site-packages/sklearn/svm/_base.py:1295: ConvergenceWarning: Liblinear failed to converge, increase the number of iterations.
  warnings.warn(
/tmp/claude-0/-home-user/cd3bd136-ab75-5641-9c58-438f3eb543f9/scratchpad/venv/lib/python3.11/site-packages/sklearn/svm/_base.py:1295: ConvergenceWarning: Liblinear failed to converge, increase the number of iterations.
  warnings.warn(
/tmp/claude-0/-home-user/cd3bd136-ab75-5641-9c58-438f3eb543f9/scratchpad/venv/lib/python3.11/site-packages/sklearn/svm/_base.py:1295: ConvergenceWarning: Liblinear failed to converge, increase the number of iterations.
  warnings.warn(
/tmp/claude-0/-home-user/cd3bd136-ab75-5641-9c58-438f3eb543f9/scratchpad/venv/lib/python3.11/site-packages/sklearn/svm/_base.py:1295: ConvergenceWarning: Liblinear failed to converge, increase the number of iterations.
  warnings.warn(


...

/tmp/claude-0/-home-user/cd3bd136-ab75-5641-9c58-438f3eb543f9/scratchpad/venv/lib/python3.11/site-packages/sklearn/svm/_base.py:1295: ConvergenceWarning: Liblinear failed to converge, increase the number of iterations.
  warnings.warn(
/tmp/claude-0/-home-user/cd3bd136-ab75-5641-9c58-438f3eb543f9/scratchpad/venv/lib/python3.11/site-packages/sklearn/svm/_base.py:1295: ConvergenceWarning: Liblinear failed to converge, increase the number of iterations.
  warnings.warn(
/tmp/claude-0/-home-user/cd3bd136-ab75-5641-9c58-438f3eb543f9/scratchpad/venv/lib/python3.11/site-packages/sklearn/svm/_base.py:1295: ConvergenceWarning: Liblinear failed to converge, increase the number of iterations.
  warnings.warn(


/tmp/claude-0/-home-user/cd3bd136-ab75-5641-9c58-438f3eb543f9/scratchpad/venv/lib/python3.11/site-packages/sklearn/svm/_base.py:1295: ConvergenceWarning: Liblinear failed to converge, increase the number of iterations.
  warnings.warn(
/tmp/claude-0/-home-user/cd3bd136-ab75-5641-9c58-438f3eb543f9/scratchpad/venv/lib/python3.11/site-packages/sklearn/svm/_base.py:1295: ConvergenceWarning: Liblinear failed to converge, increase the number of iterations.
  warnings.warn(
/tmp/claude-0/-home-user/cd3bd136-ab75-5641-9c58-438f3eb543f9/scratchpad/venv/lib/python3.11/site-packages/sklearn/svm/_base.py:1295: ConvergenceWarning: Liblinear failed to converge, increase the number of iterations.
  warnings.warn(


/tmp/claude-0/-home-user/cd3bd136-ab75-5641-9c58-438f3eb543f9/scratchpad/venv/lib/python3.11/site-packages/sklearn/svm/_base.py:1295: ConvergenceWarning: Liblinear failed to converge, increase the number of iterations.
  warnings.warn(


/tmp/claude-0/-home-user/cd3bd136-ab75-5641-9c58-438f3eb543f9/scratchpad/venv/lib/python3.11/site-packages/sklearn/svm/_base.py:1295: ConvergenceWarning: Liblinear failed to converge, increase the number of iterations.
  warnings.warn(


Best Score: 0.7806984126984129
Best Hyperparameters: {'loss': 'squared_hinge', 'max_iter': 500}


In [26]:
scores = np.array(result.cv_results_['mean_test_score']).reshape(len(lsvc_params['loss']), len(lsvc_params['max_iter']))

for ind, i in enumerate(lsvc_params['loss']):
    plt.plot(lsvc_params['max_iter'], scores[ind], label='loss: ' + str(i))

plt.legend()
plt.xlabel('max_iter')
plt.ylabel('Mean score')
plt.show()

In [27]:
y_pred = result.predict(x_test)
cf_matrix = confusion_matrix(y_test, y_pred)
sns.heatmap(cf_matrix, annot=True)
print("The accuracy score is: " + str(accuracy_score(y_test, y_pred)))

The accuracy score is: 0.7861111111111111


## Decision Tree

In [28]:
from sklearn.tree import DecisionTreeClassifier
dt_params = {
    'criterion': ['gini', 'entropy'],
}
dt = DecisionTreeClassifier(random_state=42)
search = GridSearchCV(dt, dt_params, scoring='accuracy', n_jobs=-1, cv=cv)
result = search.fit(x_train, y_train)
print('Best Score: %s' % result.best_score_)
print('Best Hyperparameters: %s' % result.best_params_)


Best Score: 0.7195555555555557
Best Hyperparameters: {'criterion': 'entropy'}


In [29]:
scores = np.array(result.cv_results_['mean_test_score'])
plt.plot(dt_params['criterion'], scores)
plt.xlabel('criterion')
plt.ylabel('Mean score')
plt.show()

In [30]:
y_pred = result.predict(x_test)
cf_matrix = confusion_matrix(y_test, y_pred)
sns.heatmap(cf_matrix, annot=True)
print("The accuracy score is: " + str(accuracy_score(y_test, y_pred)))

The accuracy score is: 0.7245555555555555


## Bagging Decision Tree

In [31]:
from sklearn.ensemble import BaggingClassifier
bg_params = {
  'max_features': [i for i in range(1, 10)]
}
bg = BaggingClassifier(random_state=42)
search = GridSearchCV(bg, bg_params, scoring='accuracy', n_jobs=-1, cv=cv)
result = search.fit(x_train, y_train)
print('Best Score: %s' % result.best_score_)
print('Best Hyperparameters: %s' % result.best_params_)



Best Score: 0.7484444444444444
Best Hyperparameters: {'max_features': 9}


In [32]:
scores = np.array(result.cv_results_['mean_test_score'])
plt.plot(bg_params['max_features'], scores)
plt.xlabel('max_features')
plt.ylabel('Mean score')
plt.show()

In [33]:
y_pred = result.predict(x_test)
cf_matrix = confusion_matrix(y_test, y_pred)
sns.heatmap(cf_matrix, annot=True)
print("The accuracy score is: " + str(accuracy_score(y_test, y_pred)))

The accuracy score is: 0.7571111111111111


## Random Forest

In [34]:
from sklearn.ensemble import RandomForestClassifier
rf_params = {
    'max_depth': [10, 20, 30, 40, 50, 60, 70, 80, 90, 100, None],
    'max_features': ['sqrt', 'log2']
}
rf = RandomForestClassifier(random_state=42)
search = GridSearchCV(rf, rf_params, scoring='accuracy', n_jobs=-1, cv=cv)
result = search.fit(x_train, y_train)
print('Best Score: %s' % result.best_score_)
print('Best Hyperparameters: %s' % result.best_params_)


Best Score: 0.7949206349206349
Best Hyperparameters: {'max_depth': 30, 'max_features': 'sqrt'}


In [35]:
scores = np.array(result.cv_results_['mean_test_score']).reshape(len(rf_params['max_features']), len(rf_params['max_depth']))

for ind, i in enumerate(rf_params['max_features']):
    plt.plot(rf_params['max_depth'], scores[ind], label='max_features: ' + str(i))

plt.legend()
plt.xlabel('max_depth')
plt.ylabel('Mean score')
plt.show()

In [36]:
y_pred = result.predict(x_test)
cf_matrix = confusion_matrix(y_test, y_pred)
sns.heatmap(cf_matrix, annot=True)
print("The accuracy score is: " + str(accuracy_score(y_test, y_pred)))

The accuracy score is: 0.7972222222222223
